# Explorador visual con búsqueda en amplitud (BFS)
### Proyecto 1 — Fundamentos de Inteligencia Artificial
Universidad Tecnológica de la Huasteca Hidalguense

**Integrantes:**
- Iván — Matrícula: 20241110
- Isaí Pascual Cruz — Matrícula: 20241018

Este notebook contiene **todo el proyecto en un solo archivo**, dividido en
celdas independientes (no todo en una sola celda): cada celda cubre una
parte del programa y se ejecuta en orden, de arriba hacia abajo.

**Nota sobre la visualización:** la versión de escritorio de este proyecto
usa una ventana de Tkinter. Google Colab no tiene entorno gráfico de
escritorio (no hay una pantalla donde abrir una ventana), así que aquí la
visualización se hace con `matplotlib`, mostrando exactamente los mismos
colores, la misma leyenda y las mismas métricas, pero como una animación
que se reproduce dentro del propio notebook.


## 1. Importaciones
Todo lo usado aquí viene incluido en Colab: no hace falta instalar nada.

In [1]:
import json
import csv
import time
import random
from pathlib import Path
from collections import deque

import matplotlib.pyplot as plt
import matplotlib.animation as animation
from IPython.display import HTML, display


## 2. Algoritmo BFS (equivalente a `bfs.py`)
Búsqueda en amplitud propia, sin librerías externas de búsqueda (no se usa
NetworkX, pathfinding ni scipy). Cola FIFO con `deque`. El diccionario
`parent` marca un estado como visitado en el momento en que **entra** a la
cola (no cuando se expande), y guarda además quién es su padre. La meta se
comprueba al **retirar** un estado de la cola, para garantizar la
profundidad mínima real.

In [2]:
DIRECCIONES = [(-1, 0), (1, 0), (0, -1), (0, 1)]  # arriba, abajo, izquierda, derecha


def vecinos(grid, celda):
    """Devuelve las celdas libres adyacentes a 'celda' (sin diagonales)."""
    filas, columnas = len(grid), len(grid[0])
    f, c = celda
    for df, dc in DIRECCIONES:
        nf, nc = f + df, c + dc
        if 0 <= nf < filas and 0 <= nc < columnas and grid[nf][nc] == 0:
            yield (nf, nc)


def reconstruir_camino(parent, meta):
    """Sigue los padres desde la meta hasta el inicio y devuelve el camino."""
    camino = []
    actual = meta
    while actual is not None:
        camino.append(actual)
        actual = parent[actual]
    camino.reverse()
    return camino


def bfs(grid, inicio, meta, registrar_pasos=True):
    """
    Ejecuta BFS desde 'inicio' hasta 'meta' (grid: 0 = libre, 1 = obstaculo).

    Devuelve un diccionario con:
      camino, profundidad, generados, expandidos, visitados,
      frontera_maxima, tiempo_ejecucion, pasos (snapshots para animar,
      cada uno con expandido/frontera/visitados/meta_encontrada).
    """
    inicio, meta = tuple(inicio), tuple(meta)
    t0 = time.perf_counter()

    if grid[inicio[0]][inicio[1]] != 0 or grid[meta[0]][meta[1]] != 0:
        return {  # inicio o meta no transitables: fracaso inmediato
            "camino": None, "profundidad": None,
            "generados": 0, "expandidos": 0, "visitados": 0,
            "frontera_maxima": 0,
            "tiempo_ejecucion": time.perf_counter() - t0,
            "pasos": [],
        }

    frontera = deque([inicio])
    parent = {inicio: None}
    expandidos = 0
    frontera_maxima = len(frontera)
    pasos = []
    camino = None

    while frontera:
        estado = frontera.popleft()
        expandidos += 1
        es_meta = (estado == meta)

        if registrar_pasos:
            pasos.append({
                "expandido": estado,
                "frontera": list(frontera),
                "visitados": list(parent.keys()),
                "meta_encontrada": es_meta,
            })

        if es_meta:
            camino = reconstruir_camino(parent, meta)
            break

        for vecino in vecinos(grid, estado):
            if vecino in parent:
                continue  # ya alcanzado antes: no se agrega de nuevo
            parent[vecino] = estado
            frontera.append(vecino)

        frontera_maxima = max(frontera_maxima, len(frontera))

    return {
        "camino": camino,
        "profundidad": (len(camino) - 1) if camino else None,
        "generados": len(parent),
        "expandidos": expandidos,
        "visitados": len(parent),
        "frontera_maxima": frontera_maxima,
        "tiempo_ejecucion": time.perf_counter() - t0,
        "pasos": pasos,
    }


## 3. Generación y validación de mapas (equivalente a `maze.py`)
Construcción de la semilla a partir de ambas matrículas, generación del
mapa principal cumpliendo las restricciones obligatorias, generación de
los casos de prueba adicionales, y guardar/cargar en JSON (para
"conservar los mapas usados en las pruebas", como pide la consigna).

In [3]:
LIBRE = 0
OBSTACULO = 1


def construir_semilla(matricula_1: str, matricula_2: str) -> int:
    """Ordena ambas matriculas y las concatena en un entero (la semilla).

    Ordenarlas antes de unirlas evita que el resultado dependa de quien
    la escriba primero: cualquiera de los dos integrantes obtiene la
    misma semilla.
    """
    m1 = str(matricula_1).strip()
    m2 = str(matricula_2).strip()
    return int("".join(sorted([m1, m2])))


def _conectados_desde(grid, inicio):
    """Devuelve el conjunto de celdas libres alcanzables desde 'inicio'."""
    filas, columnas = len(grid), len(grid[0])
    visitados = {inicio}
    pila = [inicio]
    while pila:
        f, c = pila.pop()
        for df, dc in DIRECCIONES:
            nf, nc = f + df, c + dc
            vecino = (nf, nc)
            if 0 <= nf < filas and 0 <= nc < columnas and vecino not in visitados:
                if grid[nf][nc] == LIBRE:
                    visitados.add(vecino)
                    pila.append(vecino)
    return visitados


def _tiene_callejones(grid):
    """True si existe una celda libre con exactamente 1 vecino libre."""
    filas, columnas = len(grid), len(grid[0])
    for f in range(filas):
        for c in range(columnas):
            if grid[f][c] != LIBRE:
                continue
            libres = 0
            for df, dc in DIRECCIONES:
                nf, nc = f + df, c + dc
                if 0 <= nf < filas and 0 <= nc < columnas and grid[nf][nc] == LIBRE:
                    libres += 1
            if libres == 1:
                return True
    return False


def _generar_intento(rng, filas, columnas, pct_obstaculos, inicio, meta):
    """Coloca obstaculos al azar (con rng) dejando libres inicio y meta."""
    grid = [[LIBRE for _ in range(columnas)] for _ in range(filas)]
    total = filas * columnas
    n_obstaculos = int(total * pct_obstaculos)

    celdas = [(f, c) for f in range(filas) for c in range(columnas)
              if (f, c) not in (inicio, meta)]
    rng.shuffle(celdas)

    for (f, c) in celdas[:n_obstaculos]:
        grid[f][c] = OBSTACULO
    return grid


def generar_mapa(matricula_1, matricula_2, filas=25, columnas=25,
                  pct_obstaculos=0.28, longitud_minima=25, max_intentos=1000):
    """Genera un mapa reproducible que cumple todas las condiciones
    obligatorias: tamano minimo, % de obstaculos, conectividad,
    ruta optima minima y presencia de callejones sin salida."""
    if filas < 25 or columnas < 25:
        raise ValueError("El mapa debe tener al menos 25 filas y 25 columnas.")
    if not (0.20 <= pct_obstaculos <= 0.35):
        raise ValueError("El porcentaje de obstaculos debe estar entre 20% y 35%.")

    semilla_base = construir_semilla(matricula_1, matricula_2)
    inicio, meta = (0, 0), (filas - 1, columnas - 1)

    for intento in range(max_intentos):
        rng = random.Random(semilla_base + intento)
        grid = _generar_intento(rng, filas, columnas, pct_obstaculos, inicio, meta)

        if meta not in _conectados_desde(grid, inicio):
            continue

        resultado = bfs(grid, inicio, meta, registrar_pasos=False)
        if resultado["camino"] is None or resultado["profundidad"] < longitud_minima:
            continue

        if not _tiene_callejones(grid):
            continue

        return {
            "semilla": semilla_base,
            "intento": intento,
            "filas": filas,
            "columnas": columnas,
            "pct_obstaculos": pct_obstaculos,
            "inicio": list(inicio),
            "meta": list(meta),
            "grid": grid,
            "longitud_optima": resultado["profundidad"],
        }

    raise RuntimeError(
        f"No se logro generar un mapa valido tras {max_intentos} intentos; "
        "ajuste los parametros (tamano, % de obstaculos o longitud minima)."
    )


def generar_mapa_sencillo():
    """Mapa 7x7 verificable a mano: muro con un unico hueco en la fila 3.
    Ruta optima esperada = distancia Manhattan (0,0)->(6,6) = 12 movimientos."""
    filas, columnas = 7, 7
    grid = [[LIBRE for _ in range(columnas)] for _ in range(filas)]
    for f in range(filas):
        if f != 3:
            grid[f][3] = OBSTACULO
    inicio, meta = (0, 0), (6, 6)
    return {
        "semilla": None,
        "filas": filas,
        "columnas": columnas,
        "pct_obstaculos": None,
        "inicio": list(inicio),
        "meta": list(meta),
        "grid": grid,
        "descripcion": "Caso sencillo verificable a mano (ruta optima esperada: 12 movimientos)",
    }


def generar_mapa_estres(matricula_1, matricula_2, filas=30, columnas=30,
                         pct_obstaculos=0.35):
    """Mapa grande con el porcentaje maximo de obstaculos permitido."""
    return generar_mapa(
        matricula_1, matricula_2,
        filas=filas, columnas=columnas,
        pct_obstaculos=pct_obstaculos,
        longitud_minima=1,
    )


def guardar_mapa(mapa: dict, ruta: str):
    """Guarda un mapa como JSON, creando la carpeta destino si falta."""
    Path(ruta).parent.mkdir(parents=True, exist_ok=True)
    with open(ruta, "w", encoding="utf-8") as f:
        json.dump(mapa, f, ensure_ascii=False, indent=2)


def cargar_mapa(ruta: str) -> dict:
    """Lee un mapa guardado en JSON y lo devuelve como diccionario."""
    with open(ruta, "r", encoding="utf-8") as f:
        return json.load(f)


## 4. Semilla del equipo y generación de los 3 mapas de prueba
(equivalente a `generar_mapas.py`)

Con las mismas matrículas, esto siempre genera el mismo mapa principal,
sin importar cuántas veces se ejecute esta celda. Los tres mapas se
guardan como `.json` dentro de la carpeta `mapas/` de esta sesión de
Colab, para conservarlos como evidencia (tal como pide la consigna).

In [4]:
MATRICULA_1 = "20241110"  # IVAN
MATRICULA_2 = "20241018"  # ISAI PASCUAL CRUZ

CARPETA_MAPAS = Path("mapas")

print("Generando mapa principal (25x25, semilla de ambas matriculas)...")
mapa_principal = generar_mapa(MATRICULA_1, MATRICULA_2)
guardar_mapa(mapa_principal, str(CARPETA_MAPAS / "1_mapa_principal.json"))
print(f"  Semilla: {mapa_principal['semilla']}")
print(f"  Ruta optima: {mapa_principal['longitud_optima']} movimientos")

print("Generando mapa sencillo (verificable a mano)...")
mapa_sencillo = generar_mapa_sencillo()
guardar_mapa(mapa_sencillo, str(CARPETA_MAPAS / "2_mapa_sencillo.json"))
print(f"  {mapa_sencillo['descripcion']}")

print("Generando mapa de estres (35% de obstaculos)...")
mapa_estres = generar_mapa_estres(MATRICULA_1, MATRICULA_2)
guardar_mapa(mapa_estres, str(CARPETA_MAPAS / "3_mapa_estres.json"))
print(f"  Ruta optima: {mapa_estres['longitud_optima']} movimientos")

print(f"\nMapas guardados en: {CARPETA_MAPAS.resolve()}")


Generando mapa principal (25x25, semilla de ambas matriculas)...
  Semilla: 2024101820241110
  Ruta optima: 52 movimientos
Generando mapa sencillo (verificable a mano)...
  Caso sencillo verificable a mano (ruta optima esperada: 12 movimientos)
Generando mapa de estres (35% de obstaculos)...
  Ruta optima: 60 movimientos

Mapas guardados en: /tmp/claude-0/-home-claude/6cb51b2b-f5c9-57f2-9b1c-53ccacad9b3b/scratchpad/colab/mapas


## 5. Pruebas por consola sobre los 3 mapas
(equivalente a `ejecutar_pruebas.py`)

Corre BFS sobre los tres mapas, guarda un resumen en `resultados/metricas.csv`
y compara la longitud calculada para el mapa sencillo contra el valor
esperado a mano (verificación real con `assert`, no solo un mensaje).

In [5]:
CARPETA_RESULTADOS = Path("resultados")
CARPETA_RESULTADOS.mkdir(parents=True, exist_ok=True)

CASOS = [
    ("Mapa principal", mapa_principal),
    ("Mapa sencillo", mapa_sencillo),
    ("Mapa de estres", mapa_estres),
]

RUTA_OPTIMA_ESPERADA_SENCILLO = 12  # calculada a mano: distancia Manhattan (0,0)->(6,6)

filas_csv = []
for nombre, mapa in CASOS:
    grid = mapa["grid"]
    inicio = tuple(mapa["inicio"])
    meta = tuple(mapa["meta"])

    resultado = bfs(grid, inicio, meta, registrar_pasos=False)

    print(f"\n=== {nombre} ===")
    print(f"Tamano: {len(grid)}x{len(grid[0])}  Inicio: {inicio}  Meta: {meta}")
    print(f"Solucion encontrada: {resultado['camino'] is not None}")
    print(f"Longitud del camino: {resultado['profundidad']}")
    print(f"Generados: {resultado['generados']}  Expandidos: {resultado['expandidos']}  "
          f"Visitados: {resultado['visitados']}  Frontera max.: {resultado['frontera_maxima']}")
    print(f"Tiempo: {resultado['tiempo_ejecucion']*1000:.3f} ms")

    filas_csv.append({
        "mapa": nombre,
        "filas": len(grid),
        "columnas": len(grid[0]),
        "solucion_encontrada": resultado["camino"] is not None,
        "longitud_camino": resultado["profundidad"],
        "nodos_generados": resultado["generados"],
        "nodos_expandidos": resultado["expandidos"],
        "estados_visitados": resultado["visitados"],
        "frontera_maxima": resultado["frontera_maxima"],
        "tiempo_ms": round(resultado["tiempo_ejecucion"] * 1000, 3),
    })

ruta_csv = CARPETA_RESULTADOS / "metricas.csv"
with open(ruta_csv, "w", newline="", encoding="utf-8") as f:
    escritor = csv.DictWriter(f, fieldnames=list(filas_csv[0].keys()))
    escritor.writeheader()
    escritor.writerows(filas_csv)
print(f"\nMetricas guardadas en: {ruta_csv.resolve()}")

resultado_sencillo = next(f for f in filas_csv if f["mapa"] == "Mapa sencillo")
obtenido = resultado_sencillo["longitud_camino"]
coincide = obtenido == RUTA_OPTIMA_ESPERADA_SENCILLO
print(f"\nVerificacion manual (mapa sencillo): esperado={RUTA_OPTIMA_ESPERADA_SENCILLO}, "
      f"obtenido={obtenido}, coincide={coincide}")
assert coincide, "La longitud calculada no coincide con la verificacion manual."



=== Mapa principal ===
Tamano: 25x25  Inicio: (0, 0)  Meta: (24, 24)
Solucion encontrada: True
Longitud del camino: 52
Generados: 440  Expandidos: 439  Visitados: 440  Frontera max.: 26
Tiempo: 0.972 ms

=== Mapa sencillo ===
Tamano: 7x7  Inicio: (0, 0)  Meta: (6, 6)
Solucion encontrada: True
Longitud del camino: 12
Generados: 43  Expandidos: 43  Visitados: 43  Frontera max.: 7
Tiempo: 0.112 ms

=== Mapa de estres ===
Tamano: 30x30  Inicio: (0, 0)  Meta: (29, 29)
Solucion encontrada: True
Longitud del camino: 60
Generados: 391  Expandidos: 390  Visitados: 391  Frontera max.: 17
Tiempo: 0.851 ms

Metricas guardadas en: /tmp/claude-0/-home-claude/6cb51b2b-f5c9-57f2-9b1c-53ccacad9b3b/scratchpad/colab/resultados/metricas.csv

Verificacion manual (mapa sencillo): esperado=12, obtenido=12, coincide=True


## 6. Visualización

Google Colab no tiene ventanas de escritorio, así que aquí no se puede usar
Tkinter. En su lugar se dibuja el mapa con `matplotlib`, usando exactamente
los mismos 8 colores y el mismo criterio que la versión de escritorio:
obstáculo, celda libre, inicio, meta, nodo actual, frontera abierta,
estados visitados y camino final. Cada paso de BFS (guardado en
`resultado["pasos"]`) se convierte en un cuadro de una animación.

In [6]:
COLORES = {
    "obstaculo": "#201F1F",
    "libre": "#fefefe",
    "inicio": "#05fb11",
    "meta": "#ff0404",
    "actual": "#fb8c00",
    "frontera": "#fff177",
    "visitado": "#1e94f5",
    "camino": "#8e24aa",
}

MAX_FRONTERA_MOSTRADA = 12  # elementos que se listan antes de resumir el resto


def _hex_a_rgb(hexcolor):
    hexcolor = hexcolor.lstrip("#")
    return tuple(int(hexcolor[i:i + 2], 16) / 255 for i in (0, 2, 4))


_RGB = {clave: _hex_a_rgb(valor) for clave, valor in COLORES.items()}


def _imagen_del_paso(grid, inicio, meta, paso):
    """Arma una imagen (filas x columnas x 3) con el color de cada celda
    para un paso de BFS, con la misma prioridad que usa la version de
    escritorio (main.py -> _dibujar)."""
    filas, columnas = len(grid), len(grid[0])
    visitados = set(paso["visitados"]) if paso else set()
    frontera_set = set(paso["frontera"]) if paso else set()
    actual = paso["expandido"] if paso else None
    camino_final = set(paso["camino_final"]) if paso and paso.get("camino_final") else set()

    img = [[None] * columnas for _ in range(filas)]
    for f in range(filas):
        for c in range(columnas):
            celda = (f, c)
            if grid[f][c] == 1:
                color = _RGB["obstaculo"]
            elif celda in camino_final:
                color = _RGB["camino"]
            elif celda == actual:
                color = _RGB["actual"]
            elif celda in frontera_set:
                color = _RGB["frontera"]
            elif celda in visitados:
                color = _RGB["visitado"]
            else:
                color = _RGB["libre"]

            if celda == inicio:
                color = _RGB["inicio"]
            elif celda == meta:
                color = _RGB["meta"]
            img[f][c] = color
    return img


def mostrar_leyenda():
    """Dibuja una sola vez la leyenda de colores (equivalente al panel
    'Leyenda' de la version de escritorio)."""
    etiquetas = [
        ("obstaculo", "Obstaculo"), ("libre", "Celda libre"),
        ("inicio", "Inicio"), ("meta", "Meta"),
        ("actual", "Nodo actual"), ("frontera", "Frontera abierta"),
        ("visitado", "Estados visitados"), ("camino", "Camino final"),
    ]
    fig, ax = plt.subplots(figsize=(6, 1.6))
    ax.axis("off")
    for i, (clave, texto) in enumerate(etiquetas):
        x = (i % 4) * 1.5
        y = 1 - (i // 4)
        ax.add_patch(plt.Rectangle((x, y), 0.25, 0.25, color=COLORES[clave]))
        ax.text(x + 0.35, y + 0.05, texto, fontsize=9, va="bottom")
    ax.set_xlim(-0.2, 6.2)
    ax.set_ylim(-0.5, 2)
    plt.tight_layout()
    plt.show()


def animar_busqueda(nombre_mapa, mapa, resultado, intervalo_ms=60):
    """Construye la animacion paso a paso de BFS para un mapa y la
    devuelve como reproductor HTML (con controles de reproduccion,
    pausa y avance de cuadro, integrados por matplotlib/JSHTML)."""
    grid = mapa["grid"]
    inicio, meta = tuple(mapa["inicio"]), tuple(mapa["meta"])
    pasos = resultado["pasos"]

    # Al ultimo paso (donde se encuentra la meta) se le agrega el camino
    # final ya reconstruido, para pintarlo de morado en ese cuadro.
    pasos_dibujo = [dict(p) for p in pasos]
    if pasos_dibujo and pasos_dibujo[-1]["meta_encontrada"] and resultado["camino"]:
        pasos_dibujo[-1]["camino_final"] = resultado["camino"]

    fig, ax = plt.subplots(figsize=(5, 5))
    ax.set_xticks([])
    ax.set_yticks([])
    im = ax.imshow(_imagen_del_paso(grid, inicio, meta, pasos_dibujo[0] if pasos_dibujo else None))
    titulo = ax.set_title("")

    def actualizar(i):
        paso = pasos_dibujo[i]
        im.set_data(_imagen_del_paso(grid, inicio, meta, paso))
        frontera = paso["frontera"]
        if len(frontera) > MAX_FRONTERA_MOSTRADA:
            frontera_txt = f"{frontera[:MAX_FRONTERA_MOSTRADA]}... (+{len(frontera) - MAX_FRONTERA_MOSTRADA} mas)"
        else:
            frontera_txt = f"{frontera}"
        titulo.set_text(
            f"{nombre_mapa} — paso {i + 1}/{len(pasos_dibujo)}\n"
            f"Frontera FIFO: {frontera_txt}"
        )
        return im, titulo

    anim = animation.FuncAnimation(
        fig, actualizar, frames=len(pasos_dibujo), interval=intervalo_ms, blit=False,
    )
    plt.close(fig)  # evita que se muestre un cuadro estatico duplicado
    return anim


def imprimir_metricas_finales(nombre_mapa, resultado):
    """Imprime las 8 metricas exigidas por la rubrica al terminar."""
    r = resultado
    estado = "Solucion encontrada" if r["camino"] else "Sin solucion (frontera agotada)"
    print(f"--- Metricas finales: {nombre_mapa} ---")
    print(f"{estado}")
    print(f"Longitud del camino: {r['profundidad']}")
    print(f"Nodos generados: {r['generados']}")
    print(f"Nodos expandidos: {r['expandidos']}")
    print(f"Estados visitados: {r['visitados']}")
    print(f"Profundidad de la solucion: {r['profundidad']}")
    print(f"Tamano maximo de frontera: {r['frontera_maxima']}")
    print(f"Tiempo de ejecucion: {r['tiempo_ejecucion']*1000:.3f} ms")


mostrar_leyenda()


### 6.1 Animación — Mapa principal
Esta celda corre BFS con registro de pasos y reproduce la animación. El
reproductor que aparece debajo trae sus propios controles: ▶ reproducir,
⏸ pausar, el deslizador para avanzar cuadro por cuadro (equivalente a
"Avanzar"), y volver al inicio (equivalente a "Reiniciar").

In [7]:
resultado_principal = bfs(mapa_principal["grid"], mapa_principal["inicio"], mapa_principal["meta"], registrar_pasos=True)
anim_principal = animar_busqueda("Mapa principal", mapa_principal, resultado_principal)
display(HTML(anim_principal.to_jshtml()))
imprimir_metricas_finales("Mapa principal", resultado_principal)


--- Metricas finales: Mapa principal ---
Solucion encontrada
Longitud del camino: 52
Nodos generados: 440
Nodos expandidos: 439
Estados visitados: 440
Profundidad de la solucion: 52
Tamano maximo de frontera: 26
Tiempo de ejecucion: 2.421 ms


### 6.2 Animación — Mapa sencillo (verificable a mano)

In [8]:
resultado_sencillo_anim = bfs(mapa_sencillo["grid"], mapa_sencillo["inicio"], mapa_sencillo["meta"], registrar_pasos=True)
anim_sencillo = animar_busqueda("Mapa sencillo", mapa_sencillo, resultado_sencillo_anim)
display(HTML(anim_sencillo.to_jshtml()))
imprimir_metricas_finales("Mapa sencillo", resultado_sencillo_anim)


--- Metricas finales: Mapa sencillo ---
Solucion encontrada
Longitud del camino: 12
Nodos generados: 43
Nodos expandidos: 43
Estados visitados: 43
Profundidad de la solucion: 12
Tamano maximo de frontera: 7
Tiempo de ejecucion: 0.118 ms


### 6.3 Animación — Mapa de estrés

In [9]:
resultado_estres_anim = bfs(mapa_estres["grid"], mapa_estres["inicio"], mapa_estres["meta"], registrar_pasos=True)
anim_estres = animar_busqueda("Mapa de estres", mapa_estres, resultado_estres_anim)
display(HTML(anim_estres.to_jshtml()))
imprimir_metricas_finales("Mapa de estres", resultado_estres_anim)


--- Metricas finales: Mapa de estres ---
Solucion encontrada
Longitud del camino: 60
Nodos generados: 391
Nodos expandidos: 390
Estados visitados: 391
Profundidad de la solucion: 60
Tamano maximo de frontera: 17
Tiempo de ejecucion: 2.522 ms


## 7. Cómo probar con otra semilla
El profesor puede pedir ejecutar con una semilla distinta para comprobar
que el programa no está preparado para un solo mapa. Para eso, basta con
cambiar `MATRICULA_1` y `MATRICULA_2` en la celda de la sección 4 por las
matrículas que indique, y volver a ejecutar esa celda y todas las
siguientes (Entorno de ejecución → Ejecutar después).

## Problemas conocidos
- Los archivos `.json` y `.csv` que se guardan en `mapas/` y `resultados/`
  viven únicamente en el almacenamiento temporal de esta sesión de Colab:
  se conservan mientras el notebook sigue abierto, pero se pierden si el
  entorno de ejecución se reinicia o se cierra. Para conservarlos de forma
  permanente hay que descargarlos (panel de archivos a la izquierda) o
  montar Google Drive.
- Si una celda se ejecuta fuera de orden (por ejemplo, la sección 6 antes
  que la 4), fallará porque usa variables definidas en celdas anteriores.
  Por eso, siempre debe ejecutarse de arriba hacia abajo.
